# Learned Stage-Wise Curvature Tuning on FashionMNIST

This notebook evaluates Learned Stage-Wise Curvature Tuning (SW-CT) on the FashionMNIST dataset using an ImageNet-pretrained ResNet-18.

FashionMNIST is a grayscale clothing image-classification dataset containing categories such as shirts, shoes, bags, and other apparel. Its image characteristics differ substantially from the natural RGB images used for ImageNet pretraining, providing another domain-shift setting for evaluating Learned SW-CT.

The experiments compare four conditions:

1. **Baseline** — the original pretrained ResNet with ReLU activations and a trained downstream classifier.
2. **Single-Parameter Curvature Tuning (S-CT)** — one global beta selected through validation-based exhaustive search.
3. **Learned SW-CT with fixed initialization** — four trainable stage-wise beta parameters initialized at 0.78.
4. **Learned SW-CT with random initialization** — four trainable stage-wise beta parameters independently initialized between 0.70 and 0.99.

Each condition is evaluated using seeds 42, 43, and 44.

Experiments are conducted for both 20 and 30 epochs to determine whether additional optimization improves classification performance or changes the learned stage-wise beta values.

Wall-clock execution time is also recorded to compare computational cost across Baseline, S-CT, and Learned SW-CT.

In [1]:
!nvidia-smi

Fri Oct  2 17:35:52 2026       
+-----------------------------------------------------------------------------------------+
| NVIDIA-SMI 580.82.07              Driver Version: 580.82.07      CUDA Version: 13.0     |
+-----------------------------------------+------------------------+----------------------+
| GPU  Name                 Persistence-M | Bus-Id          Disp.A | Volatile Uncorr. ECC |
| Fan  Temp   Perf          Pwr:Usage/Cap |           Memory-Usage | GPU-Util  Compute M. |
|                                         |                        |               MIG M. |
|=========================================+========================+======================|
|   0  Tesla T4                       Off |   00000000:00:04.0 Off |                    0 |
| N/A   54C    P8              9W /   70W |       0MiB /  15360MiB |      0%      Default |
|                                         |                        |                  N/A |
+-----------------------------------------+-----

In [1]:
%cd /content

!git clone -b stage-wise-ct \
    https://github.com/Syed1611/curvature-tuning-research.git

%cd /content/curvature-tuning-research/src/curvature-tuning

!git branch --show-current
!git log -1 --oneline

/content
Cloning into 'curvature-tuning-research'...
remote: Enumerating objects: 575, done.
remote: Counting objects: 100% (247/247), done.
remote: Compressing objects: 100% (123/123), done.
remote: Total 575 (delta 153), reused 181 (delta 103), pack-reused 328 (from 1)
Receiving objects: 100% (575/575), 6.93 MiB | 5.63 MiB/s, done.
Resolving deltas: 100% (284/284), done.
/content/curvature-tuning-research/src/curvature-tuning
stage-wise-ct
068c466 (HEAD -> stage-wise-ct, origin/stage-wise-ct, origin/HEAD) Updated aircraft with complete results


## Environment Setup

The repository dependencies are installed before running the experiments.

After installation, the Colab runtime should be restarted so that the required package versions are loaded correctly.

In [2]:
%pip install -q -r requirements.txt
%pip install --force-reinstall --no-cache-dir "numpy==1.26.3"

  Preparing metadata (setup.py) ... done
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 61.2/61.2 kB 9.7 MB/s eta 0:00:00
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 42.4/42.4 kB 6.2 MB/s eta 0:00:00
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 57.6/57.6 kB 9.5 MB/s eta 0:00:00
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 89.9/89.9 kB 13.3 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 18.3/18.3 MB 43.5 MB/s eta 0:00:00:00:0100:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 133.2/133.2 kB 1.9 MB/s eta 0:00:00:00:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 2.3/2.3 MB 51.0 MB/s eta 0:00:00a 0:00:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 78.4/78.4 kB 13.9 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 13.1/13.1 MB 113.8 MB/s eta 0:00:0000:010:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 8.3/8.3 MB 127.9 MB/s eta 0:00:00a 0:00:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 9.7/9.7 MB 119.6 MB/s eta 0:00:0000:0100:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━

In [1]:
%cd /content/curvature-tuning-research/src/curvature-tuning

import os
import torch

os.environ["WANDB_MODE"] = "disabled"

print("Working directory:", os.getcwd())
print("PyTorch:", torch.__version__)
print("CUDA available:", torch.cuda.is_available())

if torch.cuda.is_available():
    print("GPU:", torch.cuda.get_device_name(0))

/content/curvature-tuning-research/src/curvature-tuning
Working directory: /content/curvature-tuning-research/src/curvature-tuning
PyTorch: 2.6.0+cu124
CUDA available: True
GPU: Tesla T4


## FashionMNIST Dataset

Before running the experiments, the FashionMNIST data loaders are checked to confirm that the downstream dataset can be loaded correctly.

The same dataset split and random seed protocol are used for Baseline, S-CT, and Learned SW-CT so that the methods are compared under the same conditions.

In [2]:
from utils.data import get_data_loaders

train_loader, test_loader, val_loader = get_data_loaders(
    "imagenet_to_fashion-mnist",
    train_batch_size=32,
    test_batch_size=128,
    seed=42,
)

print("Train samples:", len(train_loader.dataset))
print("Validation samples:", len(val_loader.dataset))
print("Test samples:", len(test_loader.dataset))

images, labels = next(iter(train_loader))

print("Image batch shape:", images.shape)
print("Label batch shape:", labels.shape)
print("Labels:", labels[:10])

/usr/local/lib/python3.11/dist-packages/huggingface_hub/utils/_auth.py:104: UserWarning: 
Error while fetching `HF_TOKEN` secret value from your vault: 'Requesting secret HF_TOKEN timed out. Secrets can only be fetched when running from the Colab UI.'.
You are not authenticated with the Hugging Face Hub in this notebook.
If the error persists, please let us know by opening an issue on GitHub (https://github.com/huggingface/huggingface_hub/issues/new).
  warnings.warn(


README.md: 0.00B [00:00, ?B/s]

fashion-mnist.py: 0.00B [00:00, ?B/s]

Generating train split: 0 examples [00:00, ? examples/s]

Generating test split: 0 examples [00:00, ? examples/s]

Train samples: 48000
Validation samples: 12000
Test samples: 10000
Image batch shape: torch.Size([32, 3, 224, 224])
Label batch shape: torch.Size([32])
Labels: tensor([4, 5, 6, 2, 5, 9, 3, 5, 6, 5])


# ResNet-18 Experiments

ResNet-18 is evaluated first because it was used during the initial development of Learned SW-CT.

The experiment compares Baseline, S-CT, fixed-initialization SW-CT, and random-initialization SW-CT.

All methods use the same ImageNet-pretrained backbone, FashionMNIST dataset split, experimental seeds, and downstream training protocol.

## ResNet-18 — 20-Epoch Evaluation

The first evaluation uses 20 training epochs.

This provides the primary reference experiment and maintains compatibility with the earlier Learned SW-CT work.

### Methods

**Baseline**

The pretrained ResNet-18 retains its original ReLU activations. The backbone is frozen and only the downstream classifier is trained.

**S-CT**

The original Single-Parameter Curvature Tuning method searches over a single beta shared throughout the network. Candidate beta values from 0.70 to 1.00 are evaluated using validation performance, and the best candidate is evaluated on the test set.

The recorded S-CT execution time includes the complete beta search rather than only the final selected beta.

**Learned SW-CT — Fixed Initialization**

Four trainable beta parameters are assigned to the four ResNet stages. All four begin at beta = 0.78.

This preserves the initialization used in the original Learned SW-CT experiments.

**Learned SW-CT — Random Initialization**

Four trainable stage-wise beta parameters are initialized independently between 0.70 and 0.99.

The random initialization is generated deterministically from the experiment seed. This allows the experiment to test whether Learned SW-CT depends on the fixed 0.78 starting value while remaining reproducible.

In [3]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 42 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-02 00:14:59.444 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_fashion-mnist_resnet18_seed42_epochs20.log
2026-10-02 00:14:59.450 | INFO     | __main__:main:78 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100% 44.7M/44.7M [00:00<00:00, 206MB/s]
2026-10-02 00:16:09.803 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 00:16:09.822 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 00:16:09.822 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 00:17:52.948 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.554627, Accuracy: 12.50%
2026-10-02 00:17:53.219 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.384672, Accuracy: 12.87%
2026-10-02 00:17:53.481 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.133745, Accuracy: 27.30%
2026-10-02 00:17:

In [4]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 43 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-02 02:15:08.672 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_fashion-mnist_resnet18_seed43_epochs20.log
2026-10-02 02:15:08.675 | INFO     | __main__:main:78 - Running on cuda
2026-10-02 02:16:19.832 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 02:16:19.845 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 02:16:19.845 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 02:18:01.527 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.933057, Accuracy: 3.12%
2026-10-02 02:18:01.895 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.469695, Accuracy: 12.87%
2026-10-02 02:18:02.244 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.204006, Accuracy: 26.35%
2026-10-02 02:18:02.609 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 1.936431, Accuracy: 40.13%
2026-10-02 02:18:02.971 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, 

In [5]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 44 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-02 04:15:27.968 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_fashion-mnist_resnet18_seed44_epochs20.log
2026-10-02 04:15:27.971 | INFO     | __main__:main:78 - Running on cuda
2026-10-02 04:16:38.551 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 04:16:38.570 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 04:16:38.571 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 04:18:23.064 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.254378, Accuracy: 21.88%
2026-10-02 04:18:23.347 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.451297, Accuracy: 10.15%
2026-10-02 04:18:23.607 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.199984, Accuracy: 23.94%
2026-10-02 04:18:23.876 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 1.942387, Accuracy: 37.34%
2026-10-02 04:18:24.134 | INFO     | train:train_epoch:47 - Epoch 1, Step 400,

### Learned SW-CT with Fixed Beta Initialization

The original Learned SW-CT configuration is first reproduced using the fixed initialization:

\[[\beta_1,\beta_2,\beta_3,\beta_4]=[0.78,0.78,0.78,0.78].\]

The initial value is only a starting point. During training, the four beta parameters are optimized independently together with the downstream classifier.

These runs provide the reference against which random initialization will be compared.

In [6]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 06:15:34.882 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed42_epochs20_initfixed0.78_betalr0.01.log
2026-10-02 06:15:34.995 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 06:16:46.095 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-02 06:16:46.095 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 06:16:46.118 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-02 06:16:46.118 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 06:16:46.118 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 06:16:47.082 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.635944, Accuracy: 3.12%
2026-10-02 06:17:05.164 | INFO     | train:train_epoch:

In [3]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 08:48:28.810 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed43_epochs20_initfixed0.78_betalr0.01.log
2026-10-02 08:48:28.878 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100% 44.7M/44.7M [00:00<00:00, 155MB/s]
2026-10-02 08:49:38.144 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-02 08:49:38.144 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 08:49:38.193 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-02 08:49:38.194 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 08:49:38.194 | INFO     | __main__:main:439 - Total trainable paramete

In [4]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 10:27:39.370 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed44_epochs20_initfixed0.78_betalr0.01.log
2026-10-02 10:27:39.429 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 10:28:46.560 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-02 10:28:46.561 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 10:28:46.597 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-02 10:28:46.598 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 10:28:46.598 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 10:28:47.811 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.501830, Accuracy: 0.00%
2026-10-02 10:29:05.907 | INFO     | train:train_epoch:

### Learned SW-CT with Random Beta Initialization

The fixed beta = 0.78 initialization may raise the question of whether Learned SW-CT performs well only because its starting point was informed by the earlier S-CT experiments.

To test this dependency, each of the four stage-wise beta parameters is now initialized independently from a uniform distribution between 0.70 and 0.99.

The initialization is reproducible: the random generator is seeded using the experiment seed. Therefore, each seed always receives the same initial beta vector.

If random initialization produces similar performance to the fixed 0.78 experiment, this provides evidence that the Learned SW-CT result is not dependent on a single hand-selected initialization.

In [5]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 12:07:02.926 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed42_epochs20_initrandom_betalr0.01.log
2026-10-02 12:07:02.987 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 12:08:10.559 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-02 12:08:10.559 | INFO     | __main__:main:394 - Requested initial stage betas: [0.924447, 0.827275, 0.948993, 0.902237]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 12:08:10.582 | INFO     | __main__:main:418 - Initial stage betas: [0.924447238445282, 0.827274739742279, 0.9489933848381042, 0.9022367000579834]
2026-10-02 12:08:10.582 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 12:08:10.582 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 12:08:11.406 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.616892, Accuracy: 6.25%
2026-10-02 12:08:29.269 | INFO     | train:

In [6]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 13:46:20.549 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed43_epochs20_initrandom_betalr0.01.log
2026-10-02 13:46:20.608 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 13:47:32.247 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-02 13:47:32.247 | INFO     | __main__:main:394 - Requested initial stage betas: [0.889167, 0.712695, 0.705809, 0.943372]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 13:47:32.272 | INFO     | __main__:main:418 - Initial stage betas: [0.8891667127609253, 0.7126947641372681, 0.7058085799217224, 0.9433716535568237]
2026-10-02 13:47:32.272 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 13:47:32.272 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 13:47:33.122 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.440618, Accuracy: 12.50%
2026-10-02 13:47:50.307 | INFO     | tra

In [3]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 17:41:14.246 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed44_epochs20_initrandom_betalr0.01.log
2026-10-02 17:41:14.312 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100% 44.7M/44.7M [00:00<00:00, 180MB/s]
2026-10-02 17:42:22.612 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-02 17:42:22.613 | INFO     | __main__:main:394 - Requested initial stage betas: [0.735544, 0.774853, 0.817674, 0.981063]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 17:42:22.693 | INFO     | __main__:main:418 - Initial stage betas: [0.7355440258979797, 0.7748528122901917, 0.8176735043525696, 0.9810633659362793]
2026-10-02 17:42:22.694 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 17:42:22.694 | INFO     | __main__:main:439 - Total trai

# ResNet-18 — 30-Epoch Evaluation

The same experiments are now repeated for 30 epochs.

The purpose of increasing the training budget is to determine whether the 20-epoch results are limited by insufficient optimization.

If a method improves substantially with 30 epochs, this suggests that additional optimization is useful. If performance remains similar, it indicates that the method has largely stabilized within the original 20-epoch training budget.

All other experimental settings remain unchanged.

For random-initialization SW-CT, the same seed produces exactly the same initial four-beta vector in both the 20-epoch and 30-epoch experiments. Therefore, initialization is held constant while the training duration changes.

Execution time is again recorded to measure the computational cost of extending training from 20 to 30 epochs.

In [4]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 42 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-02 19:18:35.899 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_fashion-mnist_resnet18_seed42_epochs30.log
2026-10-02 19:18:35.902 | INFO     | __main__:main:78 - Running on cuda
2026-10-02 19:19:44.148 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 19:19:44.166 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 19:19:44.167 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 19:21:29.712 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.554627, Accuracy: 12.50%
2026-10-02 19:21:30.007 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.384672, Accuracy: 12.87%
2026-10-02 19:21:30.286 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.133745, Accuracy: 27.30%
2026-10-02 19:21:30.569 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 1.889430, Accuracy: 40.13%
2026-10-02 19:21:30.855 | INFO     | train:train_epoch:47 - Epoch 1, Step 400,

In [5]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 43 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-02 21:44:53.808 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_fashion-mnist_resnet18_seed43_epochs30.log
2026-10-02 21:44:53.812 | INFO     | __main__:main:78 - Running on cuda
2026-10-02 21:46:02.036 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 21:46:02.049 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 21:46:02.050 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 21:47:46.726 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.933057, Accuracy: 3.12%
2026-10-02 21:47:46.991 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.469695, Accuracy: 12.87%
2026-10-02 21:47:47.248 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.204006, Accuracy: 26.35%
2026-10-02 21:47:47.514 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 1.936431, Accuracy: 40.13%
2026-10-02 21:47:47.772 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, 

In [3]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 44 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-03 08:47:09.698 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_fashion-mnist_resnet18_seed44_epochs30.log
2026-10-03 08:47:09.704 | INFO     | __main__:main:78 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100% 44.7M/44.7M [00:00<00:00, 167MB/s]
2026-10-03 08:48:21.507 | INFO     | __main__:main:105 - Testing baseline...
2026-10-03 08:48:21.530 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-03 08:48:21.530 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-03 08:50:09.323 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.254378, Accuracy: 21.88%
2026-10-03 08:50:09.612 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.451297, Accuracy: 10.15%
2026-10-03 08:50:09.875 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.199984, Accuracy: 23.94%
2026-10-03 08:50:

In [3]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 16:27:43.373 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed42_epochs30_initfixed0.78_betalr0.01.log
2026-10-03 16:27:43.438 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100% 44.7M/44.7M [00:00<00:00, 186MB/s]
2026-10-03 16:28:53.583 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 16:28:53.583 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 16:28:53.674 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 16:28:53.675 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 16:28:53.675 | INFO     | __main__:main:439 - Total trainable paramete

In [4]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 18:55:56.659 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed43_epochs30_initfixed0.78_betalr0.01.log
2026-10-03 18:55:56.722 | INFO     | __main__:main:302 - Running on cuda
2026-10-03 18:57:07.542 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 18:57:07.542 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 18:57:07.564 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 18:57:07.565 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 18:57:07.565 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-03 18:57:08.414 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.487717, Accuracy: 15.62%
2026-10-03 18:57:25.991 | INFO     | train:train_epoch

In [5]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 21:24:08.406 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed44_epochs30_initfixed0.78_betalr0.01.log
2026-10-03 21:24:08.466 | INFO     | __main__:main:302 - Running on cuda
2026-10-03 21:25:17.908 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 21:25:17.909 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 21:25:17.929 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 21:25:17.930 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 21:25:17.930 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-03 21:25:18.971 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.501830, Accuracy: 0.00%
2026-10-03 21:25:36.595 | INFO     | train:train_epoch:

In [3]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-04 01:49:19.632 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed42_epochs30_initrandom_betalr0.01.log
2026-10-04 01:49:19.699 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100% 44.7M/44.7M [00:00<00:00, 219MB/s]
2026-10-04 01:50:29.421 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-04 01:50:29.421 | INFO     | __main__:main:394 - Requested initial stage betas: [0.924447, 0.827275, 0.948993, 0.902237]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-04 01:50:29.495 | INFO     | __main__:main:418 - Initial stage betas: [0.924447238445282, 0.827274739742279, 0.9489933848381042, 0.9022367000579834]
2026-10-04 01:50:29.495 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-04 01:50:29.496 | INFO     | __main__:main:439 - Total traina

In [4]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-04 04:13:43.914 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed43_epochs30_initrandom_betalr0.01.log
2026-10-04 04:13:43.975 | INFO     | __main__:main:302 - Running on cuda
2026-10-04 04:14:52.574 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-04 04:14:52.575 | INFO     | __main__:main:394 - Requested initial stage betas: [0.889167, 0.712695, 0.705809, 0.943372]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-04 04:14:52.596 | INFO     | __main__:main:418 - Initial stage betas: [0.8891667127609253, 0.7126947641372681, 0.7058085799217224, 0.9433716535568237]
2026-10-04 04:14:52.597 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-04 04:14:52.597 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-04 04:14:53.411 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.440618, Accuracy: 12.50%
2026-10-04 04:15:10.386 | INFO     | tra

In [5]:
!WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds fashion-mnist \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-04 06:38:00.112 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_fashion-mnist_resnet18_seed44_epochs30_initrandom_betalr0.01.log
2026-10-04 06:38:00.171 | INFO     | __main__:main:302 - Running on cuda
2026-10-04 06:39:09.817 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-04 06:39:09.817 | INFO     | __main__:main:394 - Requested initial stage betas: [0.735544, 0.774853, 0.817674, 0.981063]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-04 06:39:09.847 | INFO     | __main__:main:418 - Initial stage betas: [0.7355440258979797, 0.7748528122901917, 0.8176735043525696, 0.9810633659362793]
2026-10-04 06:39:09.848 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-04 06:39:09.848 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-04 06:39:10.862 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.487528, Accuracy: 9.38%
2026-10-04 06:39:28.126 | INFO     | trai